In [ ]:
import pandas as pd
pd.set_option("display.max_colwidth", 200)

In [163]:
import requests

BASE_URL = "https://data.gov.au/data/api/3/action/package_search"

params = {
    "q": "ABN OR ACN OR business",
    "rows": 6000,
    "sort": "score desc",
}

response = requests.get(BASE_URL, params=params, timeout=30)
response.raise_for_status()

data = response.json()

print("Success:", data["success"])
print("Total matches:", data["result"]["count"])

datasets = data["result"]["results"]

for ds in datasets[:5]:
    print(ds["id"], "-", ds["title"])
    # print(ds)

Success: True
Total matches: 5687
5bd7fcab-e315-42cb-8daf-50b7efc2027e - ABN Bulk Extract
3a3661a8-ee5d-4165-be5c-018634ca7202 - ABN Lookup web services
1ca29b03-220d-4c19-b34e-c7932cd4508d - Victorian Government Schools ABNs
7c356598-b048-4c1e-862f-c936041e3d81 - Research and Development tax incentive
42f46baa-b642-48b2-9f26-fc24d09d9320 - Industry breakdown of PPSR registrations


In [164]:
len(datasets)

1000

In [168]:
r

{'cache_last_updated': None,
 'cache_url': None,
 'created': '2016-07-08T17:37:28.058263',
 'datastore_active': True,
 'datastore_contains_all_records_of_source_file': False,
 'description': 'PBR agent information',
 'format': 'CSV',
 'hash': '30f7d3896bb816c94b3d240e8d408c1f',
 'id': '4b9e4af7-4f12-45f5-b5d4-e31772b85375',
 'last_modified': '2016-07-08T00:00:00',
 'metadata_modified': '2023-08-11T09:41:42.861988',
 'mimetype': None,
 'mimetype_inner': None,
 'name': 'IPGOD - 406',
 'package_id': '6a40d5a7-5886-4a96-8bca-9260ec4479ed',
 'position': 38,
 'resource_type': None,
 'size': None,
 'state': 'active',
 'url': 'https://data.gov.au/data/dataset/6a40d5a7-5886-4a96-8bca-9260ec4479ed/resource/4b9e4af7-4f12-45f5-b5d4-e31772b85375/download/ipgod406-08072016.csv',
 'url_type': 'upload',
 'wms_layer': '',
 'zip_extract': False}

In [ ]:
size = r.get("size")

if size:
     = f"{size / 1024:.2f} KB"
else:
    size_text = "Unknown"

print(
    f"  Resource: {r.get('name')}, "
    f"Format: {fmt}, "
    f"Size: {size_text}"size_text
)

  Resource: IPGOD - 406, Format: CSV, Size: Unknown


In [166]:
import requests

def get_remote_size(url):
    try:
        r = requests.head(url, allow_redirects=True, timeout=10)
        size = r.headers.get("Content-Length")

        if size:
            return int(size)
    except:
        pass

    return None

In [167]:
size = r.get("size")

if not size:
    size = get_remote_size(r.get("url"))

print(size)

800212


In [157]:
# Print all files and their formats and sizes for the top 50 datasets
for id, ds in enumerate(datasets):
    print(f"{id }. Dataset: {ds['title']}")
    for r in ds.get("resources", []):
        fmt = normalize_format(r.get("format"))
        size_mb = round((r.get("size") or 0) / 1024 , 2)
        print(f"  Resource: {r.get('name')}, Format: {fmt}, Size: {size_mb} KB")
    print("whole size of dataset: ", int(sum((r.get("size") or 0) for r in ds.get("resources", [])) / 1024 ), "KB")
    print("------------------------------------------------------------")

0. Dataset: ABN Bulk Extract
  Resource: Bulk Extract Schema, Format: XML, Size: 12.56 KB
  Resource: ABN Lookup Bulk Extract Readme, Format: PDF, Size: 150.16 KB
  Resource: ABN Bulk Extract Part 1, Format: ZIP, Size: 486738.27 KB
  Resource: ABN Bulk Extract Part 2 , Format: ZIP, Size: 486530.1 KB
  Resource: ABN Bulk Extract Resource List, Format: CSV, Size: 0.73 KB
whole size of dataset:  973431 KB
------------------------------------------------------------
1. Dataset: ABN Lookup web services
  Resource: ABN Lookup web services, Format: XML, Size: 0.0 KB
whole size of dataset:  0 KB
------------------------------------------------------------
2. Dataset: Victorian Government Schools ABNs
  Resource: Victorian Government Schools ABNs, Format: XLSX, Size: 0.0 KB
whole size of dataset:  0 KB
------------------------------------------------------------
3. Dataset: Research and Development tax incentive
  Resource: 2023-24 Report of data about Research and Development Tax Incentive ent

In [49]:
import pprint

In [156]:
pprint.pprint(datasets[0])

{'archived': False,
 'author': 'Australian Business Register',
 'author_email': None,
 'contact_point': 'ABNLookup.Support@industry.gov.au',
 'creator_user_id': 'c0ba6352-65e0-4d1a-ad29-173e02745d69',
 'duplicate_score': 1,
 'geospatial_topic': [],
 'groups': [],
 'id': '5bd7fcab-e315-42cb-8daf-50b7efc2027e',
 'isopen': False,
 'language': 'English',
 'license_id': 'cc-by',
 'license_title': 'Creative Commons Attribution 3.0 Australia',
 'license_url': 'http://creativecommons.org/licenses/by/3.0/au/',
 'maintainer': None,
 'maintainer_email': None,
 'metadata_created': '2014-09-05T05:14:28.708198',
 'metadata_modified': '2026-09-22T22:37:50.960706',
 'name': 'abn-bulk-extract',
 'notes': 'ABN Lookup Bulk Data - Australian Business Register.\r\n'
          '\r\n'
          'The extract information contains a subset of the publicly available '
          'information supplied by businesses when they register for an '
          'Australian Business Number (ABN). Current details for the fol

In [7]:
def get_dataset_count(query):
    params = {
        "q": query,
        "rows": 0,
    }
    response = requests.get(BASE_URL, params=params, timeout=30)
    response.raise_for_status()
    data = response.json()
    return data["result"]["count"]


strict_condition = "ABN AND ACN AND business"
lose_condition = "ABN OR ACN OR business"

strict_count = get_dataset_count(strict_condition)
lose_count = get_dataset_count(lose_condition)

print(f"Strict condition count: {strict_count}")
print(f"Loose condition count: {lose_count}")

Strict condition count: 247
Loose condition count: 5687


## section 2 


In [122]:
from sentence_transformers import SentenceTransformer
import numpy as np

model = SentenceTransformer("all-MiniLM-L6-v2")


Loading weights: 100%|██████████| 103/103 [00:00<00:00, 10370.48it/s]


In [123]:
def dataset_to_document(ds):
    parts = [
        ds.get("title", ""),
        ds.get("notes", ""),
        ds.get("author", ""),
        (ds.get("organization") or {}).get("title", ""),
        (ds.get("organization") or {}).get("description", ""),
    ]

    # Tags
    parts += [
        tag.get("name", "")
        for tag in ds.get("tags", [])
    ]

    # Resources
    for r in ds.get("resources", []):
        parts += [
            r.get("name", ""),
            r.get("description", ""),
            r.get("format", ""),
        ]

    return "\n".join(
        str(x).strip()
        for x in parts
        if x
    )

In [124]:
doc = dataset_to_document(datasets[0])
print(doc)

ABN Bulk Extract
ABN Lookup Bulk Data - Australian Business Register.

The extract information contains a subset of the publicly available information supplied by businesses when they register for an Australian Business Number (ABN). Current details for the following attributes are available:

+   ABN
+   ABN Status and Date
+   Entity Type
+   Legal Name
+   Business Name(s)
+   Trading Name(s)
+   State and Postcode of Main Business Location
+   ACN/ARBN
+   GST Status and Registration Date
+   Deductible Gift Recipient Status and Dates

Access to ABN Lookup data is also available via SOAP web services, you can find more information on the ABN lookup website (http://abr.business.gov.au/Webservices.aspx).
Australian Business Register
Australian Business Register
The Australian Business Register is managed by the Australian Taxation Office as a whole-of-government program.
Our vision is to contribute to improving the wellbeing of the Australian people by enhancing business productivity

In [125]:
datasets

[{'archived': False,
  'author': 'Australian Business Register',
  'author_email': None,
  'contact_point': 'ABNLookup.Support@industry.gov.au',
  'creator_user_id': 'c0ba6352-65e0-4d1a-ad29-173e02745d69',
  'duplicate_score': 1,
  'geospatial_topic': [],
  'id': '5bd7fcab-e315-42cb-8daf-50b7efc2027e',
  'isopen': False,
  'language': 'English',
  'license_id': 'cc-by',
  'license_title': 'Creative Commons Attribution 3.0 Australia',
  'license_url': 'http://creativecommons.org/licenses/by/3.0/au/',
  'maintainer': None,
  'maintainer_email': None,
  'metadata_created': '2014-09-05T05:14:28.708198',
  'metadata_modified': '2026-09-22T22:37:50.960706',
  'name': 'abn-bulk-extract',
  'notes': 'ABN Lookup Bulk Data - Australian Business Register.\r\n\r\nThe extract information contains a subset of the publicly available information supplied by businesses when they register for an Australian Business Number (ABN). Current details for the following attributes are available:\r\n\r\n+   ABN\

In [126]:
import pandas as pd

df = pd.DataFrame({
    "id": [d["id"] for d in datasets],
    "title": [d["title"] for d in datasets],
    "document": [dataset_to_document(d) for d in datasets]
})

df.head()

,id,title,document
0,5bd7fcab-e315-42cb-8daf-50b7efc2027e,ABN Bulk Extract,ABN Bulk Extract\nABN Lookup Bulk Data - Australian Business Register.\r\n\r\nThe extract information contains a subset of the publicly available information supplied by businesses when they regis...
1,3a3661a8-ee5d-4165-be5c-018634ca7202,ABN Lookup web services,ABN Lookup web services\nThe ABN Lookup web services allow you to integrate ABN Lookup validation and data into your own applications. \r\n\r\nAccess to the ABN Lookup web services is free of char...
2,1ca29b03-220d-4c19-b34e-c7932cd4508d,Victorian Government Schools ABNs,Victorian Government Schools ABNs\nThe Australian Business Number (ABN) is a unique identifier issued by the Australian Business Register (ABR) which is operated by the Australian Taxation Office ...
3,7c356598-b048-4c1e-862f-c936041e3d81,Research and Development tax incentive,"Research and Development tax incentive\nData about Research and Development tax incentive entities.\r\n\r\nThese reports contain the name, ABN/ACN, the total research and development (R&D) expendi..."
4,42f46baa-b642-48b2-9f26-fc24d09d9320,Industry breakdown of PPSR registrations,"Industry breakdown of PPSR registrations\nThe Personal Property Securities Register (PPSR) is the single, national online database of security interests in personal property in Australia. Personal..."


In [127]:
df

,id,title,document
0,5bd7fcab-e315-42cb-8daf-50b7efc2027e,ABN Bulk Extract,ABN Bulk Extract\nABN Lookup Bulk Data - Australian Business Register.\r\n\r\nThe extract information contains a subset of the publicly available information supplied by businesses when they regis...
1,3a3661a8-ee5d-4165-be5c-018634ca7202,ABN Lookup web services,ABN Lookup web services\nThe ABN Lookup web services allow you to integrate ABN Lookup validation and data into your own applications. \r\n\r\nAccess to the ABN Lookup web services is free of char...
2,1ca29b03-220d-4c19-b34e-c7932cd4508d,Victorian Government Schools ABNs,Victorian Government Schools ABNs\nThe Australian Business Number (ABN) is a unique identifier issued by the Australian Business Register (ABR) which is operated by the Australian Taxation Office ...
3,7c356598-b048-4c1e-862f-c936041e3d81,Research and Development tax incentive,"Research and Development tax incentive\nData about Research and Development tax incentive entities.\r\n\r\nThese reports contain the name, ABN/ACN, the total research and development (R&D) expendi..."
4,42f46baa-b642-48b2-9f26-fc24d09d9320,Industry breakdown of PPSR registrations,"Industry breakdown of PPSR registrations\nThe Personal Property Securities Register (PPSR) is the single, national online database of security interests in personal property in Australia. Personal..."
...,...,...,...
452,27ce2b9f-158e-4c36-9fdf-05725537d7a7,Coal Resources Spatial Data Collection 2014,Coal Resources Spatial Data Collection 2014\n## **Abstract** \n\nThis dataset and its metadata statement were supplied to the Bioregional Assessment Programme by a third party and are presented he...
453,e3e31fbd-d6dc-4837-b089-6724821264d6,Australian vegetable-growing farms: Farm financial performance web-report,Australian vegetable-growing farms: Farm financial performance web-report\nSince 2007 ABARES has conducted an annual survey of vegetable-growing farm businesses to provide industry and government ...
454,2f2c3f30-d972-47da-867c-bad12ffbfc7b,HACC MDS Annual Bulletin,"HACC MDS Annual Bulletin\n>The following publications contain information about the Home and Community Care (HACC) Program, particularly in relation to its clients, their characteristics and the s..."
455,76081b33-41de-4469-a4d9-e2b90b703ff5,Outlook scenarios for Australia's forestry sector: key drivers and opportunities,Outlook scenarios for Australia's forestry sector: key drivers and opportunities\nThis report examines three potential outlook scenarios for Australia's forestry sector using analysis of the poten...


In [128]:
from sentence_transformers import SentenceTransformer

model = SentenceTransformer("all-MiniLM-L6-v2")

target = """
A dataset containing identifiable Australian businesses or companies.
Useful fields include ABN, ACN, legal name, trading name, business name,
entity type, status, website, industry code, registration date,
business address, locality, state and postcode.
The dataset may contain registered businesses, licence holders,
suppliers, contractors, employers, builders or other identifiable entities.
"""

doc_embeddings = model.encode(
    df["document"].tolist(),
    normalize_embeddings=True,
    show_progress_bar=True
)

target_embedding = model.encode(
    target,
    normalize_embeddings=True
)

# normalized vectors => dot product == cosine similarity
df["embedding_score"] = doc_embeddings @ target_embedding

df = df.sort_values(
    "embedding_score",
    ascending=False
)

df[["title", "embedding_score"]].head(20)

Batches: 100%|██████████| 15/15 [00:01<00:00, 13.77it/s]


,title,embedding_score
0,ABN Bulk Extract,0.750809
6,ASIC - Business Names Dataset,0.668266
4,Industry breakdown of PPSR registrations,0.667724
1,ABN Lookup web services,0.661012
14,Australian Business Register - Statistics 2014-15 and 2015-16,0.658826
26,Business establishments and jobs data by business size and ANZSIC in municipality,0.628096
51,Business establishments location and industry classification,0.626905
30,Business establishments and jobs data by business size and CLUE industry in municipality,0.622777
282,GovHack 2018 – IP Australia,0.622004
2,Victorian Government Schools ABNs,0.620969


In [129]:
pd.set_option("display.max_colwidth", 200)

In [130]:
df[["title", "embedding_score"]].head(10)

,title,embedding_score
0,ABN Bulk Extract,0.750809
6,ASIC - Business Names Dataset,0.668266
4,Industry breakdown of PPSR registrations,0.667724
1,ABN Lookup web services,0.661012
14,Australian Business Register - Statistics 2014-15 and 2015-16,0.658826
26,Business establishments and jobs data by business size and ANZSIC in municipality,0.628096
51,Business establishments location and industry classification,0.626905
30,Business establishments and jobs data by business size and CLUE industry in municipality,0.622777
282,GovHack 2018 – IP Australia,0.622004
2,Victorian Government Schools ABNs,0.620969


In [131]:
df[["title", "embedding_score"]].tail(10)

,title,embedding_score
314,Congestion Levy Rates - 2020,0.181810
311,Congestion Levy Rates - 2019,0.179173
313,Congestion Levy Rates - 2018,0.173891
274,City Circle tram route,0.163457
344,"Dairy industry workforce survey, 2015-16",0.161632
56,SASP target 98 - Business research expenditure,0.160278
389,City of Yarra permit parking zones,0.156663
272,City Circle tram stops,0.152975
275,City Circle tram stops,0.152054
273,City Circle tram route,0.144948


In [132]:
df[["title", "embedding_score"]].to_csv("datasets_with_embeddings.csv")  

In [133]:
df.loc[16,'title']

'IPGOD2022'

In [134]:
import pprint

In [135]:
all_formats = set()
for ds in datasets:
    for r in ds.get("resources", []):
        fmt = r.get("format")
        if fmt:
            all_formats.add(fmt)
all_formats




{'.csv',
 '.docx',
 '.pdf',
 '.xlsx',
 'API ArcGIS Server Feature Service',
 'API ArcGIS Server Map Service',
 'ARCGIS REST SERVICE',
 'ArcGIS GeoServices REST API',
 'CSV',
 'DOC',
 'DOCX',
 'DQS - PDF',
 'FGDB',
 'GeoJSON',
 'GeoPackage',
 'HTML',
 'JSON',
 'KML',
 'KMZ',
 'LYR',
 'PDF',
 'PNG',
 'SHP',
 'SHP, TAB, FGDB, KMZ, GPKG',
 'STYLE',
 'TSV',
 'TXT',
 'URL',
 'WFS',
 'WMS',
 'XLS',
 'XLSM',
 'XLSX',
 'XML',
 'ZIP',
 'ZIP/KML',
 'csv-geo-au',
 'excel (.xlsx)',
 'excel (xlsx)',
 'marcxml',
 'microsoft excel',
 'modsxml',
 'plain',
 'tableau workbook',
 'website link',
 'word',
 'xslm',
 'xslx',
 'zip mapinfo'}

In [136]:
def normalize_format(fmt):
    fmt = (fmt or "").strip().upper()

    mapping = {
        ".CSV": "CSV",
        ".XLSX": "XLSX",
        "EXCEL (.XLSX)": "XLSX",
        "EXCEL (XLSX)": "XLSX",
        "MICROSOFT EXCEL": "XLSX",
        "XSLX": "XLSX",
        "CSV-GEO-AU": "CSV",
    }

    return mapping.get(fmt, fmt)

In [137]:
USEFUL_FORMATS = {
    "CSV",
    "TSV",
    "XLS",
    "XLSX",
    "JSON",
    "GEOJSON",
    "XML",
    "ZIP",
}

In [138]:
def has_useful_resource(ds):
    return any(
        normalize_format(r.get("format")) in USEFUL_FORMATS
        for r in ds.get("resources", [])
    )

In [139]:
datasets = [
    ds for ds in datasets
    if has_useful_resource(ds)
]

print(len(datasets))

457


In [140]:
datasets

[{'archived': False,
  'author': 'Australian Business Register',
  'author_email': None,
  'contact_point': 'ABNLookup.Support@industry.gov.au',
  'creator_user_id': 'c0ba6352-65e0-4d1a-ad29-173e02745d69',
  'duplicate_score': 1,
  'geospatial_topic': [],
  'id': '5bd7fcab-e315-42cb-8daf-50b7efc2027e',
  'isopen': False,
  'language': 'English',
  'license_id': 'cc-by',
  'license_title': 'Creative Commons Attribution 3.0 Australia',
  'license_url': 'http://creativecommons.org/licenses/by/3.0/au/',
  'maintainer': None,
  'maintainer_email': None,
  'metadata_created': '2014-09-05T05:14:28.708198',
  'metadata_modified': '2026-09-22T22:37:50.960706',
  'name': 'abn-bulk-extract',
  'notes': 'ABN Lookup Bulk Data - Australian Business Register.\r\n\r\nThe extract information contains a subset of the publicly available information supplied by businesses when they register for an Australian Business Number (ABN). Current details for the following attributes are available:\r\n\r\n+   ABN\

In [141]:
documents = [
    dataset_to_document(ds)
    for ds in datasets
]

df = pd.DataFrame({
    "id": [d["id"] for d in datasets],
    "title": [d["title"] for d in datasets],
    "document": documents,
})
df.head()

,id,title,document
0,5bd7fcab-e315-42cb-8daf-50b7efc2027e,ABN Bulk Extract,ABN Bulk Extract\nABN Lookup Bulk Data - Australian Business Register.\r\n\r\nThe extract information contains a subset of the publicly available information supplied by businesses when they regis...
1,3a3661a8-ee5d-4165-be5c-018634ca7202,ABN Lookup web services,ABN Lookup web services\nThe ABN Lookup web services allow you to integrate ABN Lookup validation and data into your own applications. \r\n\r\nAccess to the ABN Lookup web services is free of char...
2,1ca29b03-220d-4c19-b34e-c7932cd4508d,Victorian Government Schools ABNs,Victorian Government Schools ABNs\nThe Australian Business Number (ABN) is a unique identifier issued by the Australian Business Register (ABR) which is operated by the Australian Taxation Office ...
3,7c356598-b048-4c1e-862f-c936041e3d81,Research and Development tax incentive,"Research and Development tax incentive\nData about Research and Development tax incentive entities.\r\n\r\nThese reports contain the name, ABN/ACN, the total research and development (R&D) expendi..."
4,42f46baa-b642-48b2-9f26-fc24d09d9320,Industry breakdown of PPSR registrations,"Industry breakdown of PPSR registrations\nThe Personal Property Securities Register (PPSR) is the single, national online database of security interests in personal property in Australia. Personal..."


In [142]:
import pandas as pd

def get_resources(ds):
    rows = []

    for r in ds.get("resources", []):
        rows.append({
            "dataset_id": ds["id"],
            "dataset": ds["title"],
            "resource_id": r.get("id"),
            "name": r.get("name"),
            "format": r.get("format"),
            "size_mb": round((r.get("size") or 0) / 1024 / 1024, 2),
            "datastore": r.get("datastore_active"),
            "url": r.get("url"),
        })

    return pd.DataFrame(rows)



In [143]:
get_resources(datasets[0])

,dataset_id,dataset,resource_id,name,format,size_mb,datastore,url
0,5bd7fcab-e315-42cb-8daf-50b7efc2027e,ABN Bulk Extract,f3f8f8a1-590c-4d87-8285-806b093c2c69,Bulk Extract Schema,XML,0.01,False,https://data.gov.au/data/dataset/5bd7fcab-e315-42cb-8daf-50b7efc2027e/resource/f3f8f8a1-590c-4d87-8285-806b093c2c69/download/bulkextract.xsd
1,5bd7fcab-e315-42cb-8daf-50b7efc2027e,ABN Bulk Extract,3b975e4f-af2f-4de7-a20e-6dcb3f67805c,ABN Lookup Bulk Extract Readme,PDF,0.15,False,https://data.gov.au/data/dataset/5bd7fcab-e315-42cb-8daf-50b7efc2027e/resource/3b975e4f-af2f-4de7-a20e-6dcb3f67805c/download/abnlookupbulkextractreadme.pdf
2,5bd7fcab-e315-42cb-8daf-50b7efc2027e,ABN Bulk Extract,0ae4d427-6fa8-4d40-8e76-c6909b5a071b,ABN Bulk Extract Part 1,ZIP,475.33,False,https://data.gov.au/data/dataset/5bd7fcab-e315-42cb-8daf-50b7efc2027e/resource/0ae4d427-6fa8-4d40-8e76-c6909b5a071b/download/public_split_1_10.zip
3,5bd7fcab-e315-42cb-8daf-50b7efc2027e,ABN Bulk Extract,635fcb95-7864-4509-9fa7-a62a6e32b62d,ABN Bulk Extract Part 2,ZIP,475.13,False,https://data.gov.au/data/dataset/5bd7fcab-e315-42cb-8daf-50b7efc2027e/resource/635fcb95-7864-4509-9fa7-a62a6e32b62d/download/public_split_11_20.zip
4,5bd7fcab-e315-42cb-8daf-50b7efc2027e,ABN Bulk Extract,469c8c2c-0be5-45b2-90d7-c42f637f3323,ABN Bulk Extract Resource List,CSV,0.00,True,https://data.gov.au/data/dataset/5bd7fcab-e315-42cb-8daf-50b7efc2027e/resource/469c8c2c-0be5-45b2-90d7-c42f637f3323/download/abn-bulk-extract-resources.csv


In [144]:
STRONG = {
    "abn": 1.0,
    "acn": 1.0,
    "legal name": 0.9,
    "business name": 0.9,
    "trading name": 0.8,
    "licence holder": 0.8,
    "license holder": 0.8,
    "supplier": 0.7,
    "contractor": 0.6,
    "registered": 0.4,
    "address": 0.3,
}

NEGATIVE = {
    "statistics": -0.5,
    "aggregate": -0.5,
    "business counts": -0.7,
    "survey": -0.3,
}

def keyword_score(text):
    text = text.lower()
    score = 0

    for word, weight in STRONG.items():
        if word in text:
            score += weight

    for word, weight in NEGATIVE.items():
        if word in text:
            score += weight

    return max(0, min(score / 3, 1))

In [145]:
df["keyword_score"] = [
    keyword_score(doc)
    for doc in documents
]

df["final_score"] = (
    0.6 * df["embedding_score"] +
    0.4 * df["keyword_score"]
)

df = df.sort_values("final_score", ascending=False)

KeyError: 'embedding_score'

In [ ]:
KEYWORDS = {
    "abn": 5,
    "acn": 5,
    "business name": 4,
    "company name": 4,
    "legal name": 4,
    "trading name": 4,

    "licence holder": 3,
    "license holder": 3,
    "supplier": 3,
    "contractor": 3,
    "registered": 2,
    "address": 2,
    "postcode": 1,
}

NEGATIVE = {
    "statistics": -3,
    "aggregate": -3,
    "aggregated": -3,
    "business counts": -4,
    "survey": -2,
}

In [ ]:
def keyword_score(text):
    text = text.lower()

    score = 0
    matched = []

    for keyword, weight in KEYWORDS.items():
        if keyword in text:
            score += weight
            matched.append(keyword)

    for keyword, weight in NEGATIVE.items():
        if keyword in text:
            score += weight

    return max(score, 0), matched

In [ ]:
scores = df["document"].apply(keyword_score)

df["keyword_score"] = scores.apply(lambda x: x[0])
df["matched_keywords"] = scores.apply(lambda x: x[1])

In [ ]:
df["keyword_score_norm"] = (
    df["keyword_score"] / df["keyword_score"].max()
)

In [ ]:
df

,id,title,document,embedding_score,keyword_score,matched_keywords,keyword_score_norm
0,5bd7fcab-e315-42cb-8daf-50b7efc2027e,ABN Bulk Extract,ABN Bulk Extract\nABN Lookup Bulk Data - Australian Business Register.\r\n\r\nThe extract information contains a subset of the publicly available information supplied by businesses when they regis...,0.750809,23,"[abn, acn, business name, legal name, trading name, postcode]",1.000000
6,bc515135-4bb6-4d50-957a-3713709a76d3,ASIC - Business Names Dataset,ASIC - Business Names Dataset\n###Update April 2025 ###\r\n\r\nThe BN_RENEW_DT field has been removed and is no longer available in this dataset. \r\n\r\n###Update October 2018 - frequency change ...,0.668266,9,"[abn, business name]",0.391304
4,42f46baa-b642-48b2-9f26-fc24d09d9320,Industry breakdown of PPSR registrations,"Industry breakdown of PPSR registrations\nThe Personal Property Securities Register (PPSR) is the single, national online database of security interests in personal property in Australia. Personal...",0.667724,4,"[acn, registered]",0.173913
1,3a3661a8-ee5d-4165-be5c-018634ca7202,ABN Lookup web services,ABN Lookup web services\nThe ABN Lookup web services allow you to integrate ABN Lookup validation and data into your own applications. \r\n\r\nAccess to the ABN Lookup web services is free of char...,0.661012,10,"[abn, acn]",0.434783
14,8fc2e133-29f4-4123-a977-b245b32e62df,Australian Business Register - Statistics 2014-15 and 2015-16,"Australian Business Register - Statistics 2014-15 and 2015-16\nA series of tables providing an overview of Australian Business Number, populations, registrations and cancellations for the 2014-15 ...",0.658826,2,[abn],0.086957
...,...,...,...,...,...,...,...
56,996a3dd5-3659-4bfa-a8b7-47187fc2182f,SASP target 98 - Business research expenditure,"SASP target 98 - Business research expenditure\nIncrease business expenditure on research and development to 1.5% of GSP by 2014, and increase to 2.0% by 2020.\nDept of the Premier and Cabinet\nD...",0.160278,0,[],0.000000
389,a4af49a7-3cd0-4e95-abfa-3c1744cebec9,City of Yarra permit parking zones,City of Yarra permit parking zones\nThe City of Yarra local government area is divided into 24 parking zones. Permits are valid only in the zone where you live or operate a business. This data ass...,0.156663,0,[],0.000000
272,06d7c0ff-9324-43fb-b15d-6332ef6383a9,City Circle tram stops,"City Circle tram stops\nThe City Circle tram service operates within Melbourne's central business district. The service operates in a circular route passing major tourist attractions, as well as l...",0.152975,0,[],0.000000
275,61e9dc3d-32a8-49ac-96af-2b828dc4cf70,City Circle tram stops,"City Circle tram stops\nThe City Circle tram service operates within Melbourne's central business district. The service operates in a circular route passing major tourist attractions, as well as l...",0.152054,0,[],0.000000


In [ ]:
df["final_score"] = (
    0.6 * df["embedding_score"] +
    0.4 * df["keyword_score_norm"]
)

In [ ]:
df_out = df.drop(columns=["document"], errors="ignore")
df_out.sort_values("final_score", ascending=False, inplace=True,ignore_index=True)
df_out.to_csv("datasets_with_scores.csv", index=True)
df_out.head(30)

,id,title,embedding_score,keyword_score,matched_keywords,keyword_score_norm,final_score
0,5bd7fcab-e315-42cb-8daf-50b7efc2027e,ABN Bulk Extract,0.750809,23,"[abn, acn, business name, legal name, trading name, postcode]",1.000000,0.850486
1,a7bbbf64-e2ef-4d96-9fb4-0aea73ada2af,ASIC – Australian Financial Services Authorised Representative Dataset,0.537476,17,"[abn, acn, business name, address, postcode]",0.739130,0.618138
2,7b8656f9-606d-4337-af29-66b89b2eeefb,ASIC - Company Dataset,0.585730,14,"[abn, acn, company name]",0.608696,0.594917
3,fa0b0d71-b8b8-4af8-bc59-0b000ce0d5e4,ASIC – Credit Licensee Dataset,0.549025,15,"[abn, acn, business name, postcode]",0.652174,0.590285
4,3a3661a8-ee5d-4165-be5c-018634ca7202,ABN Lookup web services,0.661012,10,"[abn, acn]",0.434783,0.570520
5,bc515135-4bb6-4d50-957a-3713709a76d3,ASIC - Business Names Dataset,0.668266,9,"[abn, business name]",0.391304,0.557481
6,4117fdec-3eff-44a1-9b78-869f7ec5c409,ASIC - Registered Auditor Dataset,0.603601,10,"[acn, registered, address, postcode]",0.434783,0.536074
7,ab7eddce-84df-4098-bc8f-500d0d9776d1,ASIC - Australian Financial Services Licensee Dataset,0.516589,13,"[abn, acn, address, postcode]",0.565217,0.536040
8,a3b6d445-3a00-409a-8b49-53dc62b823bf,ASIC – Credit Representative Dataset,0.571259,11,"[abn, acn, postcode]",0.478261,0.534060
9,6a40d5a7-5886-4a96-8bca-9260ec4479ed,[Superceded] Intellectual Property Government Open Data 2016,0.527454,10,"[abn, acn]",0.434783,0.490386


In [ ]:
sample = df_out.head(50).sample(20, random_state=20)

sample

,id,title,embedding_score,keyword_score,matched_keywords,keyword_score_norm,final_score
12,b69d57f5-f9e0-4935-b6f4-1008f979dc94,[Superseded] Intellectual Property Government Open Data 2015,0.476731,10,"[abn, acn]",0.434783,0.459952
14,c9a9380f-5685-4ec4-a156-3bc17fdd58a5,[Superseded] Intellectual Property Government Open Data 2014,0.464135,10,"[abn, acn]",0.434783,0.452394
4,3a3661a8-ee5d-4165-be5c-018634ca7202,ABN Lookup web services,0.661012,10,"[abn, acn]",0.434783,0.570520
8,a3b6d445-3a00-409a-8b49-53dc62b823bf,ASIC – Credit Representative Dataset,0.571259,11,"[abn, acn, postcode]",0.478261,0.534060
45,11e281a4-28a2-4deb-9823-a527ecf7172d,Business Activity,0.596928,0,[],0.000000,0.358157
1,a7bbbf64-e2ef-4d96-9fb4-0aea73ada2af,ASIC – Australian Financial Services Authorised Representative Dataset,0.537476,17,"[abn, acn, business name, address, postcode]",0.739130,0.618138
25,2f40102e-1ea3-4b13-bbff-f217435ce992,"Bar, tavern, pub patron capacity",0.501124,6,"[trading name, address]",0.260870,0.405022
24,4e03d50e-c62b-45d3-a9a1-565da40cf77b,Business establishments location and industry classification,0.626905,2,[address],0.086957,0.410925
47,23dc5835-97f8-466c-8db2-65bb62d311f8,Business establishments per ANZSIC in municipality,0.595207,0,[],0.000000,0.357124
23,388c5a74-fa9e-4b48-8881-95467e92fe6a,ASIC - Liquidator Dataset,0.550545,5,"[registered, address, postcode]",0.217391,0.417283


In [ ]:
sample.index

Index([12, 14, 4, 8, 45, 1, 25, 24, 47, 23, 40, 17, 18, 0, 27, 33, 36, 42, 10,
       3],
      dtype='int64')

In [ ]:
df.loc[0,'document']

'ABN Bulk Extract\nABN Lookup Bulk Data - Australian Business Register.\r\n\r\nThe extract information contains a subset of the publicly available information supplied by businesses when they register for an Australian Business Number (ABN). Current details for the following attributes are available:\r\n\r\n+   ABN\r\n+   ABN Status and Date\r\n+   Entity Type\r\n+   Legal Name\r\n+   Business Name(s)\r\n+   Trading Name(s)\r\n+   State and Postcode of Main Business Location\r\n+   ACN/ARBN\r\n+   GST Status and Registration Date\r\n+   Deductible Gift Recipient Status and Dates\r\n\r\nAccess to ABN Lookup data is also available via SOAP web services, you can find more information on the ABN lookup website (http://abr.business.gov.au/Webservices.aspx).\nAustralian Business Register\nAustralian Business Register\nThe Australian Business Register is managed by the Australian Taxation Office as a whole-of-government program.\r\nOur vision is to contribute to improving the wellbeing of the

In [ ]:
df_out

In [147]:
datasets_top_50 = [record for record in datasets if record["id"] in df_out.head(50)["id"].tolist()]

In [149]:
len(datasets_top_50)

50

Learning from Files. 

In [155]:
# Print all files and their formats and sizes for the top 50 datasets
for id, ds in enumerate(datasets_top_50):
    print(f"{id }. Dataset: {ds['title']}")
    for r in ds.get("resources", []):
        fmt = normalize_format(r.get("format"))
        size_mb = round((r.get("size") or 0) / 1024 , 2)
        print(f"  Resource: {r.get('name')}, Format: {fmt}, Size: {size_mb} KB")
    print("whole size of dataset: ", int(sum((r.get("size") or 0) for r in ds.get("resources", [])) / 1024 ), "KB")
    print("------------------------------------------------------------")

0. Dataset: ABN Bulk Extract
  Resource: Bulk Extract Schema, Format: XML, Size: 12.56 KB
  Resource: ABN Lookup Bulk Extract Readme, Format: PDF, Size: 150.16 KB
  Resource: ABN Bulk Extract Part 1, Format: ZIP, Size: 486738.27 KB
  Resource: ABN Bulk Extract Part 2 , Format: ZIP, Size: 486530.1 KB
  Resource: ABN Bulk Extract Resource List, Format: CSV, Size: 0.73 KB
whole size of dataset:  973431 KB
------------------------------------------------------------
1. Dataset: ABN Lookup web services
  Resource: ABN Lookup web services, Format: XML, Size: 0.0 KB
whole size of dataset:  0 KB
------------------------------------------------------------
2. Dataset: Victorian Government Schools ABNs
  Resource: Victorian Government Schools ABNs, Format: XLSX, Size: 0.0 KB
whole size of dataset:  0 KB
------------------------------------------------------------
3. Dataset: Research and Development tax incentive
  Resource: 2023-24 Report of data about Research and Development Tax Incentive ent